# Planet basemap parcel statistics

Choose `INPUT_MODE = "local"` to reuse downloaded tiles, or `"catalog"` to
fetch imagery from the HUB. Both modes use the same cleaning and statistics.
Local source tiles are always preserved.


In [1]:
import os
from pathlib import Path

from satellites.shared.io import read_data
from satellites.data_preparation.sources.hub.catalog_library import CatalogSearchUtils
from satellites.data_preparation.parcel_stats import PlanetBasemapZonalStats
from satellites.data_preparation.sources.planet.delivery import build_local_planet_manifest

# Reuse the adapter's densified raster-footprint calculation for coverage selection.
from satellites.data_preparation.parcel_stats.planet import _raster_footprints


In [4]:
WORK_PATH = Path("C:/work_dir")
RUN_IDENTIFIER = "volvi-2023-2024"
PARCELS_PATH = WORK_PATH / RUN_IDENTIFIER / "parcels_volvi.gpkg"
BSM_TILES_PATH = WORK_PATH / "planet_basemap_quads.gpkg"
INPUT_MODE = "local"  # "local" reuses files; "catalog" downloads from HUB.
LOCAL_TILES_PATH = WORK_PATH / "planet_local_2025_01_09"
# Catalog-mode scratch only. It is not searched for existing source tiles.
DELETE_TEMPORARY_FILES = False  # True removes only scratch files owned by this run.
SCRATCH_PATH = WORK_PATH / RUN_IDENTIFIER / "planet_scratch"
OUTPUT_DIR = WORK_PATH / RUN_IDENTIFIER / "1_planet_parcel_stats"
START_DATE = "2023-12-01"
END_DATE = "2024-09-30"
WORKING_EPSG = 2100
PARCEL_ID_FIELD = "parcel_code"
QUAD_ID_FIELD = "quad_id"
COLLECTION_ID = "PL_BSM"
ANALYSIS_PATTERN = "*quad_bandmath*.tif"  # Adjust only if catalog filenames differ.

# NDMI requires SWIR, which Planet eight-band tiles do not contain.
PLANET_INDICES = ["EVI", "NDRE", "NDVI", "NDWI", "SAVI"]
SPATIAL_STATISTICS = ["mean", "median", "sd", "min", "max", "range"]
REFLECTANCE_SCALE = 0.0001  # Fallback for DN scaled by 10000; use 1.0 for reflectance already in 0-1 units.


## Parcels and intersecting quads
CRS metadata is required. The extractor repairs polygon geometries while preserving
multipart parcels, identifiers and source attributes. Do not explode multipart
parcels into duplicate IDs. Copy any label enrichment from your original notebook
here if those labels are not already stored in the parcel file.


In [5]:
gdf_parcels = read_data(str(PARCELS_PATH))
gdf_tiles = read_data(str(BSM_TILES_PATH))
if gdf_parcels.crs is None or gdf_tiles.crs is None:
    raise ValueError("Parcels and tile grid must have explicit CRS metadata")
gdf_tiles = gdf_tiles.to_crs(WORKING_EPSG)
if INPUT_MODE not in {"local", "catalog"}:
    raise ValueError('INPUT_MODE must be "local" or "catalog"')
if INPUT_MODE == "local":
    local_manifest = build_local_planet_manifest(
        LOCAL_TILES_PATH, start_date=START_DATE, end_date=END_DATE,
    )
    # A local tile selection may cover only part of the parcel dataset.
    # Select covered parcels explicitly and save excluded ones for inspection.
    gdf_tiles = gdf_tiles[gdf_tiles[QUAD_ID_FIELD].astype(str).isin(local_manifest.quad_id)].copy()
    footprints = _raster_footprints(local_manifest, WORKING_EPSG)
    metric_parcels = gdf_parcels.to_crs(WORKING_EPSG)
    covered = metric_parcels.geometry.notna()
    # A parcel needs complete coverage in every requested month, not just one.
    for _, month_tiles in footprints.groupby("period_start"):
        coverage = month_tiles.geometry.union_all().buffer(1e-6)
        covered &= metric_parcels.geometry.covered_by(coverage)
    OUTPUT_DIR.mkdir(parents=True, exist_ok=True)
    if (~covered).any():
        gdf_parcels.loc[~covered].to_parquet(OUTPUT_DIR / "outside_local_tiles.geoparquet", index=False)
    print(f"Local coverage: {covered.sum()} parcels; {(~covered).sum()} excluded")
    gdf_parcels = gdf_parcels.loc[covered].copy()
    # The extractor also checks actual raster footprints for every month.

extractor = PlanetBasemapZonalStats(
    parcels=gdf_parcels, start_date=START_DATE, end_date=END_DATE,
    output_dir=OUTPUT_DIR, working_epsg=WORKING_EPSG,
    parcel_id_field=PARCEL_ID_FIELD,
    resolution_metres=5, batch_size_metres=2000, buffer_metres=100,
    max_cube_bytes=512_000_000,
    indices=PLANET_INDICES, reflectance_scale=REFLECTANCE_SCALE,
    spatial_statistics=SPATIAL_STATISTICS,
    remove_outliers=True, iqr_quantiles=(0.1, 0.9), iqr_multiplier=1.5,
    iqr_min_valid_pixels=20, fill_nulls=True,
    temporal_fill_mode="bidirectional",  # Matches 1_parcel_stats; use past_only for causal features.
    minimum_parcel_pixels=3, minimum_observed_fraction_for_fill=0.20,
    spatial_fill_window_sizes=(3, 5), interpolation_method="nearest",
    interpolation_max_distance_in_meters=500,
)
# Select tiles intersecting the parcels; run_catalog assigns each parcel once.
study_area = extractor.parcels.to_crs(WORKING_EPSG).geometry.union_all()
gdf_tiles = gdf_tiles[gdf_tiles.intersects(study_area)].copy()
if gdf_tiles.empty:
    raise ValueError("No Planet quads intersect the study area")
print(f"{len(extractor.parcels)} parcels; {len(gdf_tiles)} quads")
gdf_tiles

Reading file: C:/work_dir/volvi-2023-2024/parcels_volvi.gpkg
Reading file: C:/work_dir/planet_basemap_quads.gpkg
Local coverage: 28699 parcels; 0 excluded


2026-09-11 20:42:11,945 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.orchestrator | Prepared 28699 valid parcels.
2026-09-11 20:42:11,956 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.orchestrator | Log files: orchestration=C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\satellite_zonal_stats.log, source=C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\satellite_source.log, raster filling=C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\satellite_raster_filling.log, parcel statistics=C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\satellite_parcel_statistics.log.
2026-09-11 20:42:11,957 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.orchestrator | Source=Planet Basemaps, optical bands=['B1', 'B2', 'B3', 'B4', 'B5', 'B6', 'B7', 'B8'], optical indices=['EVI', 'NDRE', 'NDVI', 'NDWI', 'SAVI'], parcel statistics=['mean', 'median', 'sd', 'min', 'max', 'range'], remove_outliers=True, iqr_quantiles=(0.1, 0.9), iqr_multiplier=1.5, and fill_nulls=True, tempora

28699 parcels; 9 quads


,quad_id,order,geometry
142,1154-1279,1,"POLYGON ((403040.525 4522128.149, 417858.596 4..."
143,1155-1279,1,"POLYGON ((417858.596 4521948.745, 432676.555 4..."
175,1154-1278,1,"POLYGON ((402847.063 4507352.299, 417694.754 4..."
176,1155-1278,1,"POLYGON ((417694.754 4507173.02, 432542.328 45..."
177,1156-1278,1,"POLYGON ((432542.328 4507023.462, 447389.806 4..."
208,1154-1277,1,"POLYGON ((402653.742 4492547.181, 417531.03 44..."
209,1155-1277,1,"POLYGON ((417531.03 4492368.031, 432408.198 44..."
210,1156-1277,1,"POLYGON ((432408.198 4492218.58, 447285.267 44..."
211,1157-1277,1,"POLYGON ((447285.267 4492098.827, 462162.259 4..."


## Connect to the catalog (catalog mode only)
Local mode needs no catalog connection or credentials.

In [ ]:
if INPUT_MODE == "catalog":
    catalog = CatalogSearchUtils(
        catalog_endpoint=os.environ["CATALOG_URL"],
        client_id=os.getenv("CATALOG_CLIENT_ID", "internal"), verbose=True,
    )


## Calculate parcel statistics
Tiles are aligned to a common 5 m grid. The first eight TIFF bands follow Planet
order: coastal blue, blue, green I, green, yellow, red, red edge, NIR.
TIFF nodata and masks are respected. TIFF scale/offset metadata takes precedence;
otherwise REFLECTANCE_SCALE converts stored values to reflectance before cleaning.
Use 0.0001 for DN scaled by 10000, or 1.0 for tiles already in reflectance units.
Physical-band statistics are consequently in reflectance units.

Indices are calculated per pixel after cleaning, then each requested statistic
is calculated over parcel pixels:
- EVI = 2.5 * (B8 - B6) / (B8 + 6 * B6 - 7.5 * B2 + 1)
- NDRE = (B8 - B7) / (B8 + B7)
- NDVI = (B8 - B6) / (B8 + B6), replacing the TIFF ninth band
- NDWI = (B4 - B8) / (B4 + B8), matching the existing green/NIR definition
- SAVI = 1.5 * (B8 - B6) / (B8 + B6 + 0.5)

Zero denominators become null. NDMI = (NIR - SWIR) / (NIR + SWIR) cannot
be calculated from these tiles because they lack SWIR. Requesting it raises an
explicit error rather than substituting another band.

[Planet band order and reflectance scaling](https://support.planet.com/hc/en-us/articles/115013886368-How-is-the-Surface-Reflectance-Product-Provided)

IQR cleaning and filling use each buffered processing batch. Batch size, resolution
and buffer affect results. Cleaning needs several times the raw cube RAM; reduce
batch size if necessary. Downstream feature selection must use Planet band names.

### Input paths and retention

`LOCAL_TILES_PATH` is the existing raster directory used in local mode. It is
never deleted. `SCRATCH_PATH` is only used for new catalog downloads and
intermediate cubes; it does not discover or reuse your local tiles.

In catalog mode, `DELETE_TEMPORARY_FILES = False` retains those scratch files,
including after errors. Set it to `True` to remove only the unique directories
created by the extraction. The scratch root itself and pre-existing files remain.
Keeping scratch files can use considerable disk space and does not automatically
make them a reusable download cache. Local mode retains its intermediate cubes
in `OUTPUT_DIR`; the catalog scratch flag has no effect on local mode.

Catalog mode processes buffered tile groups and months sequentially. Neighboring
quads intersecting a batch buffer also supply pixels. Completed batch tables can
be reused with `resume=True`.


In [6]:
if INPUT_MODE == "local":
    merged_gdf = extractor.run(local_manifest)
else:
    merged_gdf = extractor.run_catalog(
        catalog, gdf_tiles, scratch_dir=SCRATCH_PATH,
        collection_id=COLLECTION_ID, quad_id_field=QUAD_ID_FIELD,
        analysis_pattern=ANALYSIS_PATTERN,
        resume=True,
        delete_temporary_files=DELETE_TEMPORARY_FILES,
    )
geoparquet_path = OUTPUT_DIR / extractor.PARCEL_OUTPUT_FILE_NAME
print(f"Saved {len(merged_gdf)} parcels and {len(merged_gdf.columns)} columns: {geoparquet_path}")
merged_gdf.head()


2026-09-11 20:42:35,659 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.orchestrator | Processing Planet batch 1 (2 parcels)
2026-09-11 20:42:36,172 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.parcels | Reading temporal pixel cube C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\f5b9f600ff45aab05380\batch_1.nc.
2026-09-11 20:42:36,375 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.filling | Starting temporal fill (bidirectional) for batch 1, variable B1, period 2023-12-01: 327 null pixels.
2026-09-11 20:42:36,377 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.filling | Starting temporal fill (bidirectional) for batch 1, variable B1, period 2024-01-01: 278 null pixels.
2026-09-11 20:42:36,377 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.filling | Starting temporal fill (bidirectional) for batch 1, variable B1, period 2024-02-01: 286 null pixels.
2026-09-11 20:42:36,377 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104

Writing file: C:/work_dir/volvi-2023-2024/1_planet_parcel_stats/monthly_cubes/f5b9f600ff45aab05380/batch_1_cleaning_report.partial.parquet


2026-09-11 20:42:36,825 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.parcels | Saved completed cleaning checkpoint C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\f5b9f600ff45aab05380\batch_1_cleaned.nc.
2026-09-11 20:42:36,961 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.parcels | Saved completed post-index checkpoint C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\f5b9f600ff45aab05380\batch_1_final.nc.
2026-09-11 20:42:36,963 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.parcels | Removed intermediate cleaning raster C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\f5b9f600ff45aab05380\batch_1_cleaned.nc; raw data and audit remain available.
2026-09-11 20:42:36,981 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.parcels | Calculated ['mean', 'median', 'sd', 'min', 'max', 'range'] locally for 2 parcels from batch_1.nc.
2026-09-11 20:42:36,990 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.o

Writing file: C:/work_dir/volvi-2023-2024/1_planet_parcel_stats/monthly_cubes/c9666e81aad52a3c853e/batch_2_cleaning_report.partial.parquet


2026-09-11 20:42:37,998 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.orchestrator | Processing Planet batch 3 (86 parcels)
2026-09-11 20:42:39,190 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.parcels | Reading temporal pixel cube C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\96420d342fc2024d1223\batch_3.nc.
2026-09-11 20:42:39,489 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.filling | Starting temporal fill (bidirectional) for batch 3, variable B1, period 2023-12-01: 939 null pixels.
2026-09-11 20:42:39,490 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.filling | Starting temporal fill (bidirectional) for batch 3, variable B1, period 2024-01-01: 720 null pixels.
2026-09-11 20:42:39,490 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.filling | Starting temporal fill (bidirectional) for batch 3, variable B1, period 2024-02-01: 969 null pixels.
2026-09-11 20:42:39,491 | INFO | parcel_stats_pipeline.41d3c004e1.237763746310

...

2026-09-11 20:55:20,421 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.parcels | Saved completed post-index checkpoint C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\92e0e2034dedbed6fd13\batch_184_final.nc.
2026-09-11 20:55:20,425 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.parcels | Removed intermediate cleaning raster C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\monthly_cubes\92e0e2034dedbed6fd13\batch_184_cleaned.nc; raw data and audit remain available.
2026-09-11 20:55:20,588 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.parcels | Calculated ['mean', 'median', 'sd', 'min', 'max', 'range'] locally for 48 parcels from batch_184.nc.
2026-09-11 20:55:20,596 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.orchestrator | Processing Planet batch 185 (12 parcels)
2026-09-11 20:55:20,933 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.parcels | Reading temporal pixel cube C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\m

Writing file: C:/work_dir/volvi-2023-2024/1_planet_parcel_stats/monthly_cubes/4b370c5ddfa76afb4905/batch_185_cleaning_report.partial.parquet


2026-09-11 20:55:21,451 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.parcels | Calculated ['mean', 'median', 'sd', 'min', 'max', 'range'] locally for 12 parcels from batch_185.nc.
2026-09-11 20:55:25,321 | INFO | parcel_stats_pipeline.41d3c004e1.2377637463104.parcels | Reshaped 286990 parcel-period rows into 28699 ML-ready parcel rows with 1040 dated features in EPSG:2100.


Saved 28699 parcels and 1065 columns: C:\work_dir\volvi-2023-2024\1_planet_parcel_stats\satellite_parcel_time_stats.geoparquet


,parcel_code,initial_label_code,initial_label,predicted_label_code,predicted_label,prediction_probability,set_type,geometry,batch_number,intersected_pixel_count,...,SAVI_variance__20231201,SAVI_variance__20240101,SAVI_variance__20240201,SAVI_variance__20240301,SAVI_variance__20240401,SAVI_variance__20240501,SAVI_variance__20240601,SAVI_variance__20240701,SAVI_variance__20240801,SAVI_variance__20240901
0,51480984,110,wheat,119,grass_fodders,0.347813,train,"MULTIPOLYGON (((423723.022 4513149.345, 423769...",101,298,...,0.000112,0.000315,0.000385,0.004067,0.002530,0.001549,0.000292,0.000260,0.000245,0.000316
1,237535570,110,wheat,110,wheat,0.677429,train,"MULTIPOLYGON (((412455.851 4524641.592, 412393...",34,357,...,0.000076,0.000067,0.000072,0.001896,0.002725,0.000726,0.000107,0.000136,0.000231,0.000603
2,237535579,110,wheat,110,wheat,0.298195,test,"MULTIPOLYGON (((412401.035 4523218.598, 412407...",33,161,...,0.000386,0.000454,0.000423,0.000690,0.000794,0.000351,0.000080,0.000140,0.000234,0.000406
3,237535543,119,grass_fodders,129,fallow,0.420473,test,"MULTIPOLYGON (((412129.805 4523563.227, 412128...",33,154,...,0.000158,0.000165,0.000176,0.001260,0.001662,0.000404,0.001301,0.001170,0.001088,0.000662
4,237535582,110,wheat,110,wheat,0.431326,test,"MULTIPOLYGON (((412513.852 4522829.275, 412578...",33,147,...,0.000127,0.000143,0.000241,0.000998,0.001109,0.000430,0.000077,0.000095,0.000139,0.000992


## Outputs

- `satellite_parcel_time_stats.geoparquet`: parcel attributes, quality metrics and dated statistics.
- `satellite_parcel_annual_stats.geoparquet`: annual median features.
- `satellite_pixel_cleaning_report.csv`: cleaning audit.
- `planet_tile_manifest.csv`: source paths and, in catalog mode, their deletion status.
- `outside_local_tiles.geoparquet`: parcels excluded from local processing, when present.

Local source files are preserved. Catalog scratch retention follows
`DELETE_TEMPORARY_FILES`; result tables are always retained in `OUTPUT_DIR`.
